   # Práctica de IA + PAM: BirdNET


D. Velasco-Montero, 2026

En esta sesión de trabajo con Jupyter veremos la implementación en Python de **[BirdNET](https://birdnet-team.github.io/BirdNET-Analyzer/)** y lo aplicaremos a un conjunto de audios del dataset [xeno-canto](https://xeno-canto.org/).

> Audios &rarr; BirdNET &rarr; Especies y confianza &rarr; Resultados

Usaremos las siguientes librerías de Python:
* [Numpy](https://numpy.org/)
* [Matplotlib](https://matplotlib.org/)
* [Pandas](https://pandas.pydata.org/)
* [birdnetlib](https://github.com/joeweiss/birdnetlib)

## 0. Instalar y cargar librerías en Python

Si no tenemos instaladas las librerías, habría que ejecutar lo siguiente:

In [98]:
!pip install matplotlib Pillow numpy
!pip install birdnetlib

Cargamos las librerías:

In [1]:
from pathlib import Path

from birdnetlib import Recording
from birdnetlib.analyzer import Analyzer

import pandas as pd
import numpy as np

C:\Users\delia\AppData\Local\Programs\Spyder\Python\lib\site-packages\pydub\utils.py:170: RuntimeWarning: Couldn't find ffmpeg or avconv - defaulting to ffmpeg, but may not work
  warn("Couldn't find ffmpeg or avconv - defaulting to ffmpeg, but may not work", RuntimeWarning)


## 1. Objetivos


En esta práctica aprenderemos a:

- Ejecutar BirdNET sobre audios de monitorización acústica pasiva.
- Interpretar las detecciones.
- Analizar la probabilidad de cada detección.
- Ajustar el umbral de confianza.
- Visualizar los resultados.

In [19]:
# Lista de audios
folder = "xenocanto_example_files/"

audios = sorted(Path(folder).glob("*.wav"))
print(f"{len(audios)} audios encontrados.")

3 audios encontrados.


Escucha estos audios.

¿CQué especies aparecen? ¿En qué instantes?

In [20]:
# Reproducirlos
from IPython.display import Audio, display

for audio in audios:
    print(audio)
    display(Audio(audio))

xenocanto_example_files\XC1157693 - Agateador europeo - Certhia brachydactyla.wav


xenocanto_example_files\XC1157746 - Cigüeñuela común - Himantopus himantopus.wav


xenocanto_example_files\XC1157754 - Vencejo pálido - Apus pallidus.wav


## 2. Ejecutar BirdNET

Primero cargamos el modelo de BirdNET. Es un modelo basado en una red neuronal convolucional que trabaja sobre espectrogramas de audio.

In [11]:
analyzer = Analyzer()

load model
Model loaded.
Labels loaded.
Labels loaded.
load_species_list_model
Meta model loaded.


Podemos ver cómo funciona el modelo sobre el primer ejemplo de audio. El modelo trabaja dividiendo el fichero completo de audio en intrevalos (chunks) de 3 segundos, cada uno de los cuales se transforma en un espectrograma, que es analizado por la red neuronal.

In [30]:
audio = audios[1]

recording = Recording(
    analyzer,
    audio,
    min_conf=0.1
)

recording.analyze()

read_audio_data
read_audio_data: complete, read  10 chunks.
analyze_recording xenocanto_example_files\XC1157746 - Cigüeñuela común - Himantopus himantopus.wav


Podemos ver cómo son las detecciones. Estas contienen:
- el nombre común y nombre científico de la especie detectada (es capaz de detectar más de 6000 especies del mundo)
- el intervalo temporal de 3 segundos dónde ha sido detectada
- la confianza asociada

In [31]:
recording.detections[0]

{'common_name': 'Black-winged Stilt',
 'scientific_name': 'Himantopus himantopus',
 'start_time': 0.0,
 'end_time': 3.0,
 'confidence': 0.7535883784294128}

Podemos ver todas las detecciones que ha realizado el modelo. Se puede observar que el modelo puede detectar varias especies en el mismo intervalo temporal (por ejemplo, entre los instantes t=0 y t=3), cada una con su confianza asociada. Vemos que en la mayoría de los casos la especie detectada (*Himantopus himantopus*) corresponde con la especie que está vocalizando en este fichero "XC1157746 - Cigüeñuela común - Himantopus himantopus.wav".

In [34]:
df = pd.DataFrame(recording.detections)
df

,common_name,scientific_name,start_time,end_time,confidence
0,Black-winged Stilt,Himantopus himantopus,0.0,3.0,0.753588
1,Black-necked Stilt,Himantopus mexicanus,0.0,3.0,0.263992
2,White Wagtail,Motacilla alba,6.0,9.0,0.542618
3,Tawny Pipit,Anthus campestris,6.0,9.0,0.115974
4,Black-winged Stilt,Himantopus himantopus,9.0,12.0,0.982024
5,Black-winged Stilt,Himantopus himantopus,12.0,15.0,0.990615
6,Black-winged Stilt,Himantopus himantopus,15.0,18.0,0.991169
7,Black-winged Stilt,Himantopus himantopus,18.0,21.0,0.977546
8,Black-winged Stilt,Himantopus himantopus,21.0,24.0,0.921765
9,Black-winged Stilt,Himantopus himantopus,24.0,27.0,0.987563


Analizamos el resto de ficheros de audio:

In [21]:
carpeta_audio = Path(folder)

resultados = []

for archivo in carpeta_audio.glob("*.wav"):

    print("Procesando:", archivo.name)

    recording = Recording(
        analyzer,
        str(archivo),
        min_conf=0.1
    )

    recording.analyze()

    for det in recording.detections:
        det["file"] = archivo.name
        resultados.append(det)


df = pd.DataFrame(resultados)

df

Procesando: XC1157693 - Agateador europeo - Certhia brachydactyla.wav
read_audio_data
read_audio_data: complete, read  9 chunks.
analyze_recording xenocanto_example_files\XC1157693 - Agateador europeo - Certhia brachydactyla.wav
Procesando: XC1157746 - Cigüeñuela común - Himantopus himantopus.wav
read_audio_data
read_audio_data: complete, read  10 chunks.
analyze_recording xenocanto_example_files\XC1157746 - Cigüeñuela común - Himantopus himantopus.wav
Procesando: XC1157754 - Vencejo pálido - Apus pallidus.wav
read_audio_data
read_audio_data: complete, read  2 chunks.
analyze_recording xenocanto_example_files\XC1157754 - Vencejo pálido - Apus pallidus.wav


,common_name,scientific_name,start_time,end_time,confidence,file
0,Short-toed Treecreeper,Certhia brachydactyla,0.0,3.0,0.972280,XC1157693 - Agateador europeo - Certhia brachy...
1,Short-toed Treecreeper,Certhia brachydactyla,3.0,6.0,0.970376,XC1157693 - Agateador europeo - Certhia brachy...
2,Short-toed Treecreeper,Certhia brachydactyla,6.0,9.0,0.980516,XC1157693 - Agateador europeo - Certhia brachy...
3,Short-toed Treecreeper,Certhia brachydactyla,9.0,12.0,0.979325,XC1157693 - Agateador europeo - Certhia brachy...
4,Short-toed Treecreeper,Certhia brachydactyla,12.0,15.0,0.931326,XC1157693 - Agateador europeo - Certhia brachy...
5,Short-toed Treecreeper,Certhia brachydactyla,15.0,18.0,0.943679,XC1157693 - Agateador europeo - Certhia brachy...
6,Short-toed Treecreeper,Certhia brachydactyla,18.0,21.0,0.977035,XC1157693 - Agateador europeo - Certhia brachy...
7,Short-toed Treecreeper,Certhia brachydactyla,21.0,24.0,0.946043,XC1157693 - Agateador europeo - Certhia brachy...
8,Black-winged Stilt,Himantopus himantopus,0.0,3.0,0.753588,XC1157746 - Cigüeñuela común - Himantopus hima...
9,Black-necked Stilt,Himantopus mexicanus,0.0,3.0,0.263992,XC1157746 - Cigüeñuela común - Himantopus hima...


De nuevo, vemos identificaciones correctas de *Certhia brachydactyla* en el primer fichero, de *Himantopus himantopus* en el segundo y de *Apus pallidus* en el tercero. 

Además, se han identificado otras especies (por ejemplo *Motacilla alba*), aunque con menor confianza (0.54). Para eliminar estas predicciones con menor confianza, podemos realizar un filtrado:

In [24]:
# Filtrado de detecciones
df_filtrado = df[df["confidence"] >= 0.95]
df_filtrado

,common_name,scientific_name,start_time,end_time,confidence,file
0,Short-toed Treecreeper,Certhia brachydactyla,0.0,3.0,0.972280,XC1157693 - Agateador europeo - Certhia brachy...
1,Short-toed Treecreeper,Certhia brachydactyla,3.0,6.0,0.970376,XC1157693 - Agateador europeo - Certhia brachy...
2,Short-toed Treecreeper,Certhia brachydactyla,6.0,9.0,0.980516,XC1157693 - Agateador europeo - Certhia brachy...
3,Short-toed Treecreeper,Certhia brachydactyla,9.0,12.0,0.979325,XC1157693 - Agateador europeo - Certhia brachy...
6,Short-toed Treecreeper,Certhia brachydactyla,18.0,21.0,0.977035,XC1157693 - Agateador europeo - Certhia brachy...
12,Black-winged Stilt,Himantopus himantopus,9.0,12.0,0.982024,XC1157746 - Cigüeñuela común - Himantopus hima...
13,Black-winged Stilt,Himantopus himantopus,12.0,15.0,0.990615,XC1157746 - Cigüeñuela común - Himantopus hima...
14,Black-winged Stilt,Himantopus himantopus,15.0,18.0,0.991169,XC1157746 - Cigüeñuela común - Himantopus hima...
15,Black-winged Stilt,Himantopus himantopus,18.0,21.0,0.977546,XC1157746 - Cigüeñuela común - Himantopus hima...
17,Black-winged Stilt,Himantopus himantopus,24.0,27.0,0.987563,XC1157746 - Cigüeñuela común - Himantopus hima...


Ahora todas las predicciones son correctas.

## Alternativa

También podemos usar la [Demo de BirdNET](https://birdnet.cornell.edu/demo/?lang=es) 